In [0]:
%sql
DROP DATABASE IF EXISTS gold CASCADE;

In [0]:
%sql
CREATE DATABASE gold

In [0]:
spark.conf.set("fs.azure.account.auth.type.<storage-account>.dfs.core.windows.net", "OAuth")
spark.conf.set("fs.azure.account.oauth.provider.type.<storage-account>.dfs.core.windows.net", "org.apache.hadoop.fs.azurebfs.oauth2.ClientCredsTokenProvider")
spark.conf.set("fs.azure.account.oauth2.client.id.<storage-account>.dfs.core.windows.net", "<application-id>")
spark.conf.set("fs.azure.account.oauth2.client.secret.<storage-account>.dfs.core.windows.net", service_credential)
spark.conf.set("fs.azure.account.oauth2.client.endpoint.<storage-account>.dfs.core.windows.net", "https://login.microsoftonline.com/<directory-id>/oauth2/token")

In [0]:
from pyspark.sql.functions import *
from pyspark.sql.types import *

### Data Zone

In [0]:
silver = "abfss://silver@taxidatalakeom.dfs.core.windows.net"
gold = "abfss://gold@taxidatalakeom.dfs.core.windows.net"

In [0]:
df_zone = spark.read.format('parquet')\
                .option('inferSchema',True)\
                .option("header", True)\
                .load(f'{silver}/trip_zone')

In [0]:
df_zone.display()

LocationID,Borough,Zone,service_zone,Zone1,Zone2
1,EWR,Newark Airport,EWR,Newark Airport,null
2,Queens,Jamaica Bay,Boro Zone,Jamaica Bay,null
3,Bronx,Allerton/Pelham Gardens,Boro Zone,Allerton,Pelham Gardens
4,Manhattan,Alphabet City,Yellow Zone,Alphabet City,null
5,Staten Island,Arden Heights,Boro Zone,Arden Heights,null
6,Staten Island,Arrochar/Fort Wadsworth,Boro Zone,Arrochar,Fort Wadsworth
7,Queens,Astoria,Boro Zone,Astoria,null
8,Queens,Astoria Park,Boro Zone,Astoria Park,null
9,Queens,Auburndale,Boro Zone,Auburndale,null
10,Queens,Baisley Park,Boro Zone,Baisley Park,null


In [0]:
df_zone.write.format('delta')\
        .mode('append')\
        .option('path',f'{gold}/trip_zone')\
        .saveAsTable('gold.trip_zone')

In [0]:
%sql
select * from gold.trip_zone

LocationID,Borough,Zone,service_zone,Zone1,Zone2
1,EWR,Newark Airport,EWR,Newark Airport,null
2,Queens,Jamaica Bay,Boro Zone,Jamaica Bay,null
3,Bronx,Allerton/Pelham Gardens,Boro Zone,Allerton,Pelham Gardens
4,Manhattan,Alphabet City,Yellow Zone,Alphabet City,null
5,Staten Island,Arden Heights,Boro Zone,Arden Heights,null
6,Staten Island,Arrochar/Fort Wadsworth,Boro Zone,Arrochar,Fort Wadsworth
7,Queens,Astoria,Boro Zone,Astoria,null
8,Queens,Astoria Park,Boro Zone,Astoria Park,null
9,Queens,Auburndale,Boro Zone,Auburndale,null
10,Queens,Baisley Park,Boro Zone,Baisley Park,null


In [0]:
%sql
select * from gold.trip_zone where Borough = 'EWR'

LocationID,Borough,Zone,service_zone,Zone1,Zone2
1,EWR,Newark Airport,EWR,Newark Airport,null


### Trip Type

In [0]:
df_type = spark.read.format('parquet')\
                .option('inferSchema',True)\
                .option("header", True)\
                .load(f'{silver}/trip_type')

In [0]:
df_type.write.format('delta')\
        .mode('append')\
        .option('path',f'{gold}/trip_type')\
        .saveAsTable('gold.trip_type')

### Trips Data

In [0]:
df_trip = spark.read.parquet(
    f"{silver}/trips2023data/*.parquet"
)

In [0]:
df_trip.display()

VendorID,lpep_pickup_datetime,lpep_dropoff_datetime,store_and_fwd_flag,RatecodeID,PULocationID,DOLocationID,passenger_count,trip_distance,fare_amount,extra,mta_tax,tip_amount,tolls_amount,ehail_fee,improvement_surcharge,total_amount,payment_type,trip_type,congestion_surcharge,trip_date,trip_year,trip_month
2,2023-03-01T00:25:10Z,2023-03-01T00:35:47Z,N,1,82,196,1,2.36,13.5,1.0,0.5,0.0,0.0,null,1.0,16.0,2,1,0.0,2023-03-01,2023,3
2,2023-03-01T00:14:29Z,2023-03-01T00:25:04Z,N,1,7,7,1,0.78,-6.5,-1.0,-0.5,0.0,0.0,null,-1.0,-9.0,3,1,0.0,2023-03-01,2023,3
2,2023-03-01T00:14:29Z,2023-03-01T00:25:04Z,N,1,7,7,1,0.78,6.5,1.0,0.5,0.0,0.0,null,1.0,9.0,3,1,0.0,2023-03-01,2023,3
2,2023-02-28T22:59:46Z,2023-02-28T23:08:38Z,N,1,166,74,1,1.66,11.4,1.0,0.5,2.78,0.0,null,1.0,16.68,1,1,0.0,2023-02-28,2023,2
2,2023-03-01T00:54:03Z,2023-03-01T01:03:14Z,N,1,236,229,1,3.14,15.6,1.0,0.5,4.17,0.0,null,1.0,25.02,1,1,2.75,2023-03-01,2023,3
2,2023-03-01T01:00:09Z,2023-03-01T01:14:37Z,N,1,75,235,1,5.69,23.3,1.0,0.5,4.0,0.0,null,1.0,29.8,1,1,0.0,2023-03-01,2023,3
2,2023-03-01T00:09:45Z,2023-03-01T00:26:06Z,N,1,260,160,1,2.92,17.7,1.0,0.5,4.04,0.0,null,1.0,24.24,1,1,0.0,2023-03-01,2023,3
2,2023-03-01T00:39:30Z,2023-03-01T00:39:33Z,N,5,95,264,5,0.0,35.0,0.0,0.0,1.0,0.0,null,1.0,37.0,1,2,0.0,2023-03-01,2023,3
2,2023-03-01T00:03:07Z,2023-03-01T00:14:44Z,N,1,244,41,1,3.34,16.3,1.0,0.5,5.64,0.0,null,1.0,24.44,1,1,0.0,2023-03-01,2023,3
2,2023-03-01T00:42:56Z,2023-03-01T00:49:57Z,N,1,83,7,5,1.75,10.7,1.0,0.5,2.64,0.0,null,1.0,15.84,1,1,0.0,2023-03-01,2023,3


In [0]:
df_trip.write.format('delta')\
        .mode('append')\
        .option('path',f'{gold}/trips2023data')\
        .saveAsTable('gold.trip_trip')

### Delta Table versioning

In [0]:
%sql
select * from gold.trip_zone;

LocationID,Borough,Zone,service_zone,Zone1,Zone2
1,EWR,Newark Airport,EWR,Newark Airport,null
2,Queens,Jamaica Bay,Boro Zone,Jamaica Bay,null
3,Bronx,Allerton/Pelham Gardens,Boro Zone,Allerton,Pelham Gardens
4,Manhattan,Alphabet City,Yellow Zone,Alphabet City,null
5,Staten Island,Arden Heights,Boro Zone,Arden Heights,null
6,Staten Island,Arrochar/Fort Wadsworth,Boro Zone,Arrochar,Fort Wadsworth
7,Queens,Astoria,Boro Zone,Astoria,null
8,Queens,Astoria Park,Boro Zone,Astoria Park,null
9,Queens,Auburndale,Boro Zone,Auburndale,null
10,Queens,Baisley Park,Boro Zone,Baisley Park,null


In [0]:
%sql
update gold.trip_zone 
set Borough = 'EWR' 
where LocationID = 1;

num_affected_rows
1


In [0]:
%sql
select * from gold.trip_zone where LocationID = 1;

LocationID,Borough,Zone,service_zone,Zone1,Zone2
1,EWR,Newark Airport,EWR,Newark Airport,null


In [0]:
%sql
DELETE FROM gold.trip_zone where LocationID = 1;

num_affected_rows
1


In [0]:
%sql
DESCRIBE HISTORY gold.trip_zone;

version,timestamp,userId,userName,operation,operationParameters,job,notebook,clusterId,readVersion,isolationLevel,isBlindAppend,operationMetrics,userMetadata,engineInfo
2,2026-09-26T05:34:08Z,147260868792202,omnadarkar22@outlook.com,DELETE,"Map(predicate -> [""(LocationID#4638 = 1)""])",null,List(1036414588068375),0925-041337-ux96l90i,1,WriteSerializable,false,"Map(numRemovedFiles -> 1, numRemovedBytes -> 1843, numCopiedRows -> 0, numDeletionVectorsAdded -> 0, numDeletionVectorsRemoved -> 0, numAddedChangeFiles -> 0, executionTimeMs -> 920, numDeletionVectorsUpdated -> 0, numDeletedRows -> 1, scanTimeMs -> 778, numAddedFiles -> 0, numAddedBytes -> 0, rewriteTimeMs -> 131)",null,Databricks-Runtime/17.3.x-photon-scala2.13
1,2026-09-26T05:31:58Z,147260868792202,omnadarkar22@outlook.com,UPDATE,"Map(predicate -> [""(LocationID#4239 = 1)""])",null,List(1036414588068375),0925-041337-ux96l90i,0,WriteSerializable,false,"Map(numRemovedFiles -> 0, numRemovedBytes -> 0, numCopiedRows -> 0, numDeletionVectorsAdded -> 1, numDeletionVectorsRemoved -> 0, numAddedChangeFiles -> 0, executionTimeMs -> 4883, numDeletionVectorsUpdated -> 0, scanTimeMs -> 2334, numAddedFiles -> 1, numUpdatedRows -> 1, numAddedBytes -> 1843, rewriteTimeMs -> 2527)",null,Databricks-Runtime/17.3.x-photon-scala2.13
0,2026-09-26T05:07:24Z,147260868792202,omnadarkar22@outlook.com,CREATE TABLE AS SELECT,"Map(partitionBy -> [], clusterBy -> [], description -> null, isManaged -> false, properties -> {""delta.enableDeletionVectors"":""true""}, statsOnLoad -> true)",null,List(1036414588068375),0925-041337-ux96l90i,null,WriteSerializable,true,"Map(numFiles -> 1, numOutputRows -> 265, numOutputBytes -> 9996)",null,Databricks-Runtime/17.3.x-photon-scala2.13


In [0]:
%sql
select * from gold.trip_trip

VendorID,lpep_pickup_datetime,lpep_dropoff_datetime,store_and_fwd_flag,RatecodeID,PULocationID,DOLocationID,passenger_count,trip_distance,fare_amount,extra,mta_tax,tip_amount,tolls_amount,ehail_fee,improvement_surcharge,total_amount,payment_type,trip_type,congestion_surcharge,trip_date,trip_year,trip_month
2,2023-04-01T00:01:46Z,2023-04-01T00:11:42Z,N,1,75,42,1,2.62,13.5,1.0,0.5,3.0,0.0,null,1.0,19.0,1,1,0.0,2023-04-01,2023,4
2,2023-04-01T00:21:32Z,2023-04-01T00:53:16Z,N,1,166,107,1,6.51,33.8,1.0,0.5,7.81,0.0,null,1.0,46.86,1,1,2.75,2023-04-01,2023,4
2,2023-04-01T00:03:14Z,2023-04-01T00:16:54Z,N,1,74,238,1,2.59,15.6,1.0,0.5,2.5,0.0,null,1.0,20.6,1,1,0.0,2023-04-01,2023,4
1,2023-04-01T00:22:17Z,2023-04-01T00:27:34Z,N,1,66,33,1,0.7,6.5,1.0,1.5,2.65,0.0,null,1.0,11.65,1,1,0.0,2023-04-01,2023,4
2,2023-04-01T00:58:41Z,2023-04-01T01:21:20Z,N,1,255,225,1,4.96,25.4,1.0,0.5,5.58,0.0,null,1.0,33.48,1,1,0.0,2023-04-01,2023,4
1,2023-04-01T00:36:23Z,2023-04-01T00:57:57Z,N,1,112,140,1,7.5,32.4,3.75,1.5,5.0,0.0,null,1.0,42.65,1,1,2.75,2023-04-01,2023,4
2,2023-04-01T00:20:50Z,2023-04-01T00:45:07Z,N,1,66,158,1,4.26,24.7,1.0,0.5,3.0,0.0,null,1.0,32.95,1,1,2.75,2023-04-01,2023,4
2,2023-04-01T00:31:54Z,2023-04-01T00:36:29Z,N,1,75,263,1,0.63,6.5,1.0,0.5,1.8,0.0,null,1.0,10.8,1,1,0.0,2023-04-01,2023,4
2,2023-04-01T00:08:35Z,2023-04-01T00:11:14Z,N,1,7,7,1,0.5,5.1,1.0,0.5,1.52,0.0,null,1.0,9.12,1,1,0.0,2023-04-01,2023,4
2,2023-04-01T00:30:42Z,2023-04-01T00:37:11Z,N,1,7,179,1,1.11,7.9,1.0,0.5,2.08,0.0,null,1.0,12.48,1,1,0.0,2023-04-01,2023,4
